# Music generation using ACE Step and OpenVINO

[ACE-Step](https://ace-step.github.io/) is a novel open-source foundation model for music generation that overcomes key limitations of existing approaches and achieves state-of-the-art performance through a holistic architectural design. Current methods face inherent trade-offs between generation speed, musical coherence, and controllability. ACE-Step bridges this gap by integrating diffusion-based generation with Sana’s Deep Compression AutoEncoder (DCAE) and a lightweight linear transformer. The model achieving superior musical coherence and lyric alignment across melody, harmony, and rhythm metrics. Moreover, ACE-Step preserves fine-grained acoustic details, enabling advanced control mechanisms such as voice cloning, lyric editing, remixing, and track generation (e.g., lyric2vocal, singing2accompaniment). 


ACE-Step adapts a text-to-image diffusion framework for music generation. The core generative model is a diffusion model operating on a compressed mel spectrogram latent representation. This process is guided by conditioning information from three specialized encoders: a text prompt encoder, a lyric encoder, and a speaker encoder. Embeddings from these encoders are concatenated and integrated into the diffusion model via cross-attention mechanisms


ACE-Step can be used for generating original music from text descriptions, music remixing and style transfer, edit song lyrics. The model offers a set of controllable features that allow users to precisely control the generation process and enable targeted modifications to existing audio material, as well as perform specialized generation tasks through fine-tuning.


<img src="https://raw.githubusercontent.com/ACE-Step/ACE-Step/main/assets/ACE-Step_framework.png" width=90% style="display: block; margin: auto;" />

More details about the model can be found using the following resources: [project page](https://ace-step.github.io/), [paper](https://arxiv.org/abs/2506.00045), [original repository](https://github.com/ace-step/ACE-Step).




### Installation Instructions

This is a self-contained example that relies solely on its own code.

We recommend  running the notebook in a virtual environment. You only need a Jupyter server to start.
For details, please refer to [Installation Guide](https://github.com/openvinotoolkit/openvino_notebooks/blob/latest/README.md#-installation-guide).

<img referrerpolicy="no-referrer-when-downgrade" src="https://static.scarf.sh/a.png?x-pxid=5b5a4db0-7875-4bfb-bdbd-01698b5b1a77&file=notebooks/ace-step-music-generation/ace-step-music-generation.ipynb" />

#### Table of contents:

- [Prerequisites](#Prerequisites)
- [Music generation with ACE Step Pipeline via PyTorch](#Music-generation-with-ACE-Step-Pipeline-via-PyTorch)
    - [Download checkpoints and load PyTorch models](#Download-checkpoints-and-load-PyTorch-models)
    - [Configure parameters and generate audio](#Configure-parameters-and-generate-audio)
    - [Update audio](#Update-audio)
- [Music Generation with ACE Step via OpenVINO](#Music-Generation-with-ACE-Step-via-OpenVINO)
    - [Convert model to OpenVINO](#Convert-model-to-OpenVINO)
    - [Select inference device](#Select-inference-device)
    - [Create pipeline, read and compile models](#Create-pipeline,-read-and-compile-models)
    - [Generate audio](#Generate-audio)
    - [Update audio](#Update-audio)
- [ACE Step with LoRA](#ACE-Step-with-LoRA)
    - [Load LoRA and apply for Transformer models for ACE Step pipeline](#Load-LoRA-and-apply-for-Transformer-models-for-ACE-Step-pipeline)
    - [Convert models with LoRA and load to OpenVINO pipeline](#Convert-models-with-LoRA-and-load-to-OpenVINO-pipeline)
    - [Run Inference with LoRA](#Run-Inference-with-LoRA)
    - [Deactivate LoRA](#Deactivate-LoRA)
- [Interactive demo](#Interactive-demo)



## Prerequisites
[back to top ⬆️](#Table-of-contents:)

**Note:** FFmpeg is recommended for audio saving via `torchaudio`. If FFmpeg is not installed, a `soundfile` backend will be used as a fallback. For more information, visit the [official FFmpeg website](https://www.ffmpeg.org/).

**macOS (Homebrew):**
```bash
brew install ffmpeg
```
**Ubuntu/Debian:**
```bash
sudo apt update && sudo apt install ffmpeg
```
**Verify installation:**
```bash
ffmpeg -version
```

In [1]:
import requests
from pathlib import Path

if not Path("ov_ace_helper.py").exists():
    r = requests.get(url="https://raw.githubusercontent.com/openvinotoolkit/openvino_notebooks/latest/notebooks/ace-step-music-generation/ov_ace_helper.py")
    open("ov_ace_helper.py", "w").write(r.text)

if not Path("gradio_helper.py").exists():
    r = requests.get(url="https://raw.githubusercontent.com/openvinotoolkit/openvino_notebooks/latest/notebooks/ace-step-music-generation/gradio_helper.py")
    open("gradio_helper.py", "w").write(r.text)

if not Path("notebook_utils.py").exists():
    r = requests.get(url="https://raw.githubusercontent.com/openvinotoolkit/openvino_notebooks/latest/utils/notebook_utils.py")
    open("notebook_utils.py", "w").write(r.text)

if not Path("pip_helper.py").exists():
    r = requests.get(
        url="https://raw.githubusercontent.com/openvinotoolkit/openvino_notebooks/latest/utils/pip_helper.py",
    )
    open("pip_helper.py", "w").write(r.text)

from pip_helper import pip_install

pip_install("gradio>=4.19")

pip_install(
    "-q",
    "https://codeload.github.com/ace-step/ACE-Step/tar.gz/6ae0852b1388de6dc0cca26b31a86d711f723cb3",
    "torch==2.10",
    "torchaudio==2.10",
    "peft==0.17.1",
    "--extra-index-url",
    "https://download.pytorch.org/whl/cpu",
)

pip_install("-q", "openvino>=2026.0.0", "openvino-tokenizers>=2026.0.0", "nncf>=3.0.0")

# Import the helper early so its `torchaudio` -> `soundfile` fallback patch
# is applied before the PyTorch ACE-Step pipeline is used.
import ov_ace_helper  # noqa: F401

# Read more about telemetry collection at https://github.com/openvinotoolkit/openvino_notebooks?tab=readme-ov-file#-telemetry
from notebook_utils import collect_telemetry

collect_telemetry("ace-step-music-generation.ipynb")

  Using cached gradio-6.29.1-py3-none-any.whl.metadata (16 kB)
  Using cached brotli-1.2.0-cp312-cp312-manylinux2014_x86_64.manylinux_2_17_x86_64.whl.metadata (6.1 kB)


  Using cached fastapi-0.142.2-py3-none-any.whl.metadata (27 kB)
  Using cached gradio_client-2.7.2-py3-none-any.whl.metadata (7.1 kB)
  Using cached groovy-0.1.2-py3-none-any.whl.metadata (6.1 kB)


  Using cached hf_gradio-0.4.1-py3-none-any.whl.metadata (428 bytes)
  Using cached jinja2-3.1.6-py3-none-any.whl.metadata (2.9 kB)
  Using cached markupsafe-3.0.4-cp312-cp312-manylinux2014_x86_64.manylinux_2_17_x86_64.manylinux_2_28_x86_64.whl.metadata (2.7 kB)
  Using cached orjson-3.12.0-cp312-cp312-manylinux_2_17_x86_64.manylinux2014_x86_64.whl.metadata (41 kB)


  Using cached pandas-3.0.6-cp312-cp312-manylinux_2_24_x86_64.manylinux_2_28_x86_64.whl.metadata (79 kB)
  Using cached pydantic-2.13.5-py3-none-any.whl.metadata (110 kB)


  Using cached pydub-0.25.1-py2.py3-none-any.whl.metadata (1.4 kB)
  Using cached python_multipart-0.0.32-py3-none-any.whl.metadata (2.1 kB)
  Using cached pytz-2026.5-py2.py3-none-any.whl.metadata (22 kB)


...

   ━━━━━━━━━━━━━━━━━━━━━━━━━━━╸━━━━━━━━━━━━ 16/23 [pandas]

   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━╺━ 22/23 [gradio]

   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━╺━ 22/23 [gradio]

   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 23/23 [gradio]


FFmpeg shared libraries not found; using `soundfile` backend for audio I/O.


## Music generation with ACE Step Pipeline via PyTorch
[back to top ⬆️](#Table-of-contents:)

### Download checkpoints and load PyTorch models
[back to top ⬆️](#Table-of-contents:)

The architecture of ACE Step consists of following components.

Linear Diffusion Transformer.

Core Diffusion Model is a Linear Diffusion Transformer (DiT). DiT architecture adapts the Transformer to serve as the backbone for diffusion models, primarily replacing U-Net structures common in image generation. DiTs treat latent representations (e.g., image patches or segments of audio features) as sequences of tokens. These tokens, along with embeddings for the diffusion timestep and any conditioning information, are processed by a series of Transformer blocks. ACE-Step adapt the Linear DiT structure from Sana with several modifications. This significantly reduces model size and memory consumption; And added 1D Convolutional FeedForward Layers (FFN).

Conditioning Encoders.

To guide the generation process, the Linear DiT is conditioned on embeddings from the following encoders:
- Text Encoder: It is a mT5-base model, which generate 768-dimensional embeddings from textual prompts.
- Lyric Encoder: The lyric encoder architecture and hyperparameters are adopted from SongGen.
- Speaker Encoder: The speaker encoder processes a 10 - second unaccompanied vocal segment, which is separated by demucs, into a 512 - dimensional embedding. For full songs with vocals, embeddings from multiple such segments are averaged. A zero vector is used as the speaker embedding for instrumental tracks. The encoder, pre-trained on a large and diverse singing voice corpus, draws architectural inspiration from
PLR-OSNet, originally designed for face recognition. The model was tuned to prevents the model from over-relying on timbre information for stylistic interpretation, thereby enabling reasonable timbre generation even without explicit speaker input.

Deep Compression AutoEncoders.

For efficient latent space modeling, ACE-Step uses Deep Compression AutoEncoder (DCAE). A DCAE is an encoder to map high-dimensional input (e.g., mel-spectrograms) to a much lower-dimensional latent representation, and a decoder to reconstruct the original input from this latent code. The "deep compression" aspect implies a focus on achieving a highly compact latent space while minimizing reconstruction error. For audio, this means capturing salient acoustic features essential for perception and quality within a small number of latent variables. This not only reduces the computational burden for subsequent generative models operating in this latent space but also encourages the generative model to focus on higher-level structural and semantic aspects rather than low-level waveform details. The specific architecture of DCAE (e.g., convolutional layers, quantization if used) is optimized for this trade-off. For converting the generated mel-spectrograms back to waveform (vocoding), ACE-Step utilizes a pre-trained universal music vocoder from Fish Audio.

In [2]:
from acestep.pipeline_ace_step import ACEStepPipeline

checkpoint_dir = ""
pipeline = ACEStepPipeline(checkpoint_dir=checkpoint_dir, dtype="float32", cpu_offload=False)
pipeline.load_checkpoint(checkpoint_dir)

2026-10-06 17:09:03.217 | INFO     | acestep.pipeline_ace_step:get_checkpoint_path:178 - Download models from Hugging Face: ACE-Step/ACE-Step-v1-3.5B, cache to: 


Fetching 14 files:   0%|          | 0/14 [00:00<?, ?it/s]

config.json: 0.00B [00:00, ?B/s]

README.md: 0.00B [00:00, ?B/s]

.gitattributes: 0.00B [00:00, ?B/s]

...

diffusion_pytorch_model.safetensors:   0%|          | 0.00/6.61G [00:00<?, ?B/s]

tokenizer.json:   0%|          | 0.00/16.8M [00:00<?, ?B/s]

There are modules in ACEStepTransformer2DModel that should be kept in float32: []. Casting directly with `to()` can lead to inconsistent results; set `torch_dtype` in `from_pretrained()` instead to keep these modules in float32.


/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/.venvs/cpu/0e02466db943f1d6/lib/python3.12/site-packages/torch/nn/utils/weight_norm.py:144: FutureWarning: `torch.nn.utils.weight_norm` is deprecated in favor of `torch.nn.utils.parametrizations.weight_norm`.
  WeightNorm.apply(module, name, dim)


There are modules in MusicDCAE that should be kept in float32: []. Casting directly with `to()` can lead to inconsistent results; set `torch_dtype` in `from_pretrained()` instead to keep these modules in float32.


### Configure parameters and generate audio
[back to top ⬆️](#Table-of-contents:)

We will specify some parameters: `prompt`, `lyrics`, `infer_step` `save_path`, `audio_duration` in second, `task` and parameters related to the Entropy Rectifying Guidance `use_erg_tag`, `use_erg_lyric`, `use_erg_diffusion`, if these parameters are enabled, the temperature will be multiply to the attention to make a weaker, for example with `use_erg_lyric`, lyric condition and make better diversity.

Some other options which can be specified: `guidance_scale`, `guidance_scale_text`, `guidance_scale_lyric`, `guidance_interval` - guidance interval for the generation, `min_guidance_scale`, `guidance_interval_decay` - guidance interval decay for the generation, guidance scale will decay from guidance_scale to min_guidance_scale in the interval, `omega_scale` - Granularity scale for the generation. Higher values can reduce artifacts, `oss_steps` - optimal Steps for the generation, `audio2audio_enable` - enable Audio-to-Audio generation using a reference audio, `ref_audio_input` - reference audio for audio2audio task, `ref_audio_strength`.

More information about parameters can be found in [ACE Step repo](https://github.com/ace-step/ACE-Step).

In [3]:
import os

inputs = {
    "prompt": "country rock, folk rock, southern rock, bluegrass, country pop",
    "lyrics": "[verse]\nWoke up to the sunrise glow\nTook my heart and hit the road[inst]",
    "audio_duration": 15.0,
    "infer_step": 25,
    "use_erg_tag": False,
    "use_erg_lyric": True,
    "use_erg_diffusion": True,
    "save_path": Path("outputs").absolute().as_posix(),
    "task": "text2music",
}

if not Path(inputs["save_path"]).exists():
    os.mkdir(inputs["save_path"])

In [4]:
import IPython.display as ipd

result = pipeline(**inputs)

output_path = result[0]
display(ipd.Audio(output_path))

2026-10-06 17:19:36.856 | INFO     | acestep.pipeline_ace_step:__call__:1488 - Model loaded in 0.00 seconds.


2026-10-06 17:19:36.898 | INFO     | acestep.pipeline_ace_step:text2music_diffusion_process:847 - cfg_type: apg, guidance_scale: 15.0, omega_scale: 10.0


2026-10-06 17:19:36.899 | INFO     | acestep.pipeline_ace_step:text2music_diffusion_process:1072 - start_idx: 6, end_idx: 18, num_inference_steps: 25


  0%|          | 0/25 [00:00<?, ?it/s]

  4%|▍         | 1/25 [00:01<00:26,  1.09s/it]

...

100%|██████████| 25/25 [00:43<00:00,  1.75s/it]

  0%|          | 0/1 [00:00<?, ?it/s]

2026-10-06 17:20:25.170 | INFO     | acestep.pipeline_ace_step:save_wav_file:1390 - Provided save_path '/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs' is a directory. Appending timestamped filename.


2026-10-06 17:20:25.170 | INFO     | acestep.pipeline_ace_step:save_wav_file:1399 - Saving audio to /home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs/output_20261006172025_0.wav using backend soundfile


100%|██████████| 1/1 [00:00<00:00, 55.43it/s]

### Update audio
[back to top ⬆️](#Table-of-contents:)

ACE Step provides functions for updating audio. The following tasks are available in ACE Step for that: `retake`, `repaint`, `edit` and `extend`.
For retaking `retake_variance` and `retake_seeds` can be specified. We can edit prompt with `edit_target_prompt` or lyrics with `edit_target_lyrics`, also we can set `edit_n_min`,`edit_n_max` and `edit_n_avg`. For repainting it is possible to setup `retake_variance`, `retake_seeds`, `repaint_start` and `repaint_end` times. And extend can be configured with `repaint_start` and `repaint_end` options in seconds. Also source audio should be provided via `src_audio_path`.

Let's try to edit style of generated audio.

In [5]:
import copy

inputs_update_audio = copy.deepcopy(inputs)
inputs_update_audio.update(
    {
        "edit_target_prompt": "classical, orchestral, strings, piano, 60 bpm, elegant, emotive, timeless, instrumental",
        "edit_target_lyrics": inputs["lyrics"],
        "edit_n_min": 0.2,
        "edit_n_max": 0.4,
        "task": "edit",
        "src_audio_path": output_path,
    }
)

In [6]:
result = pipeline(**inputs_update_audio)

display(ipd.Audio(result[0]))

2026-10-06 17:20:25.631 | INFO     | acestep.pipeline_ace_step:__call__:1488 - Model loaded in 0.00 seconds.


2026-10-06 17:20:26.909 | INFO     | acestep.pipeline_ace_step:tokenize_lyrics:465 - debbug [verse] --> zh --> ['[en]', '[verse]']


2026-10-06 17:20:26.913 | INFO     | acestep.pipeline_ace_step:tokenize_lyrics:465 - debbug Woke up to the sunrise glow --> en --> ['[en]', 'w', 'ok', 'e', ' ', 'up', ' ', 'to', ' ', 'the', ' ', 'sun', 'ris', 'e', ' ', 'gl', 'ow']


2026-10-06 17:20:26.914 | INFO     | acestep.pipeline_ace_step:tokenize_lyrics:465 - debbug Took my heart and hit the road[inst] --> en --> ['[en]', 'to', 'ok', ' ', 'my', ' ', 'he', 'a', 'rt', ' ', 'and', ' ', 'h', 'it', ' ', 'the', ' ', 'ro', 'ad', '[inst]']


2026-10-06 17:20:26.915 | INFO     | acestep.pipeline_ace_step:flowedit_diffusion_process:658 - flowedit start from 5 to 10


...

100%|██████████| 25/25 [00:40<00:00,  1.62s/it]

  0%|          | 0/1 [00:00<?, ?it/s]

2026-10-06 17:21:11.982 | INFO     | acestep.pipeline_ace_step:save_wav_file:1390 - Provided save_path '/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs' is a directory. Appending timestamped filename.


2026-10-06 17:21:11.982 | INFO     | acestep.pipeline_ace_step:save_wav_file:1399 - Saving audio to /home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs/output_20261006172111_0.wav using backend soundfile


100%|██████████| 1/1 [00:00<00:00, 92.86it/s]

## Music Generation with ACE Step via OpenVINO
[back to top ⬆️](#Table-of-contents:)

### Convert model to OpenVINO
[back to top ⬆️](#Table-of-contents:)

OpenVINO supports PyTorch models via conversion to OpenVINO Intermediate Representation (IR). [OpenVINO model conversion API](https://docs.openvino.ai/2024/openvino-workflow/model-preparation.html#convert-a-model-with-python-convert-model) can be used for these purposes. `ov.convert_model` function accepts original PyTorch model instance and example input for tracing and returns `ov.Model` representing this model in OpenVINO framework. Converted model can be saved on disk using `ov.save_model` function or loading on device using `core.complie_model`.

`ov_ace_helper.py` script contains helper function for model conversion, please check its content if you interested in conversion details. 

Let's convert models to IR format. In output folder you will find tokenizer - `openvino_tokenizer.xml`, text encoder model - `ov_text_encoder_model.xml`. Lyric encoder and speaker encoder will be part of transformer models. DCAE decoder and encoder models: `ov_dcae_encoder_model.xml`, `ov_dcae_decoder_model.xml`, vocoder decoder and mel_transform models: `ov_vocoder_decode_model.xml`, `ov_vocoder_mel_transform_model.xml`. And transformer models: `ov_transformer_decoder_model.xml`, `ov_transformer_encoder_model.xml`.

In [7]:
from gradio_helper import get_model_compression_format_widgets

model_format = get_model_compression_format_widgets()
model_format

Dropdown(description='Model format:', options=('FP16', 'INT8', 'INT4'), value='FP16')

In [8]:
import nncf
from ov_ace_helper import convert_models

ov_converted_model_dir = "ov_models"
if model_format.value == "INT4":
    weights_compression_config = {"mode": nncf.CompressWeightsMode.INT4_ASYM, "group_size": 128, "ratio": 0.8}
    ov_converted_model_dir += "_int4"
elif model_format.value == "INT8":
    weights_compression_config = {"mode": nncf.CompressWeightsMode.INT8_ASYM}
    ov_converted_model_dir += "_int8"
else:
    weights_compression_config = None

convert_models(pipeline, model_dir=ov_converted_model_dir, orig_checkpoint_path=checkpoint_dir, quantization_config=weights_compression_config)

⌛ Conversion started. Be patient, it may takes some time.
⌛ Convert Tokenizer


✅ Tokenizer is converted
⌛ Convert UMT5 Encoder model


`loss_type=None` was set in the config but it is unrecognised.Using the default loss: `ForCausalLMLoss`.


✅ UMT5 Encoder model converted
⌛ Convert Sana's Deep Compression AutoEncoder model


/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/.venvs/cpu/0e02466db943f1d6/lib/python3.12/site-packages/diffusers/models/attention_processor.py:5252: TracerWarning: Converting a tensor to a Python boolean might cause the trace to be incorrect. We can't record the data flow of Python values, so this value will be treated as a constant in the future. This means that the trace might not generalize to other inputs!
  if height * width > attn.attention_head_dim:


...

/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/.venvs/cpu/0e02466db943f1d6/lib/python3.12/site-packages/acestep/models/lyrics_utils/lyric_encoder.py:743: TracerWarning: Converting a tensor to a Python boolean might cause the trace to be incorrect. We can't record the data flow of Python values, so this value will be treated as a constant in the future. This means that the trace might not generalize to other inputs!
  if self.pe.size(1) >= x.size(1) * 2 - 1:
/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/.venvs/cpu/0e02466db943f1d6/lib/python3.12/site-packages/acestep/models/lyrics_utils/lyric_encoder.py:400: TracerWarning: Converting a tensor to a Python boolean might cause the trace to be incorrect. We can't record the data flow of Python values, so this value will be treated as a constant in the future. This means that the trace might not generalize to other inputs!
  if cache.size(0) > 0:
/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/.venvs/cpu/0e02466db943f1d6/lib/python3.12/site-packages/

✅ Transformer Encoder with Entropy Rectifying Guidance model converted
⌛ Convert Transformer Decoder with Entropy Rectifying Guidance model


/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/.venvs/cpu/0e02466db943f1d6/lib/python3.12/site-packages/acestep/models/ace_step_transformer.py:84: TracerWarning: Converting a tensor to a Python boolean might cause the trace to be incorrect. We can't record the data flow of Python values, so this value will be treated as a constant in the future. This means that the trace might not generalize to other inputs!
  if seq_len > self.max_seq_len_cached:


/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/.venvs/cpu/0e02466db943f1d6/lib/python3.12/site-packages/acestep/models/ace_step_transformer.py:136: TracerWarning: Converting a tensor to a Python boolean might cause the trace to be incorrect. We can't record the data flow of Python values, so this value will be treated as a constant in the future. This means that the trace might not generalize to other inputs!
  if width > new_width:
/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/.venvs/cpu/0e02466db943f1d6/lib/python3.12/site-packages/acestep/models/ace_step_transformer.py:140: TracerWarning: Converting a tensor to a Python boolean might cause the trace to be incorrect. We can't record the data flow of Python values, so this value will be treated as a constant in the future. This means that the trace might not generalize to other inputs!
  elif width < new_width:


✅ Transformer Decoder with Entropy Rectifying Guidance model converted


### Select inference device
[back to top ⬆️](#Table-of-contents:)

Select device from dropdown list for running inference using OpenVINO

In [9]:
from notebook_utils import device_widget

device = device_widget(exclude=["NPU"])

device

Dropdown(description='Device:', options=('CPU', 'GPU', 'AUTO'), value='CPU')

### Create pipeline, read and compile models
[back to top ⬆️](#Table-of-contents:)

In [10]:
from ov_ace_helper import OVACEStepPipeline

ov_pipeline = OVACEStepPipeline()
ov_pipeline.load_models(ov_models_path=ov_converted_model_dir, device=device.value)

### Generate audio
[back to top ⬆️](#Table-of-contents:)

In [11]:
import IPython.display as ipd

ov_result = ov_pipeline(**inputs)

ov_out_audio_path = ov_result[0]
display(ipd.Audio(ov_out_audio_path))

2026-10-06 17:22:32.340 | INFO     | acestep.pipeline_ace_step:__call__:1488 - Model loaded in 0.00 seconds.


2026-10-06 17:22:32.539 | INFO     | ov_ace_helper:text2music_diffusion_process:623 - cfg_type: apg, guidance_scale: 15.0, omega_scale: 10.0


2026-10-06 17:22:32.544 | INFO     | ov_ace_helper:text2music_diffusion_process:807 - start_idx: 6, end_idx: 18, num_inference_steps: 25


  0%|          | 0/25 [00:00<?, ?it/s]

  4%|▍         | 1/25 [00:00<00:14,  1.70it/s]

...

100%|██████████| 25/25 [00:11<00:00,  2.25it/s]

  0%|          | 0/1 [00:00<?, ?it/s]

2026-10-06 17:22:45.496 | INFO     | acestep.pipeline_ace_step:save_wav_file:1390 - Provided save_path '/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs' is a directory. Appending timestamped filename.


2026-10-06 17:22:45.496 | INFO     | acestep.pipeline_ace_step:save_wav_file:1399 - Saving audio to /home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs/output_20261006172245_0.wav using backend soundfile


100%|██████████| 1/1 [00:00<00:00, 70.36it/s]

### Update audio
[back to top ⬆️](#Table-of-contents:)

In [12]:
from gradio_helper import update_audio_widget

update_audio_type = update_audio_widget()

update_audio_type

ToggleButtons(button_style='info', description='Choose next operation with audio:', index=1, options=('Retake'…

In [13]:
from gradio_helper import setup_update_audio_widgets

setup_update_audio_options, update_task = setup_update_audio_widgets(update_audio_type)

setup_update_audio_options

In [14]:
from gradio_helper import get_inputs_base_on_setup_widget

inputs_update_audio = get_inputs_base_on_setup_widget(
    base_inputs=inputs, source_audio_path=ov_out_audio_path, setup_widgets=setup_update_audio_options, task=update_task
)
print(inputs_update_audio)

{'prompt': 'country rock, folk rock, southern rock, bluegrass, country pop', 'lyrics': '[verse]\nWoke up to the sunrise glow\nTook my heart and hit the road[inst]', 'audio_duration': 15.0, 'infer_step': 25, 'use_erg_tag': False, 'use_erg_lyric': True, 'use_erg_diffusion': True, 'save_path': '/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs', 'task': 'repaint', 'src_audio_path': '/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs/output_20261006172245_0.wav', 'retake_variance': 0.2, 'repaint_start': 0.0, 'repaint_end': 4.0}


In [15]:
ov_update_result = ov_pipeline(**inputs_update_audio)

display(ipd.Audio(ov_update_result[0]))

2026-10-06 17:22:46.007 | INFO     | acestep.pipeline_ace_step:__call__:1488 - Model loaded in 0.00 seconds.


2026-10-06 17:22:46.547 | INFO     | ov_ace_helper:text2music_diffusion_process:623 - cfg_type: apg, guidance_scale: 15.0, omega_scale: 10.0


2026-10-06 17:22:46.549 | INFO     | ov_ace_helper:text2music_diffusion_process:807 - start_idx: 6, end_idx: 18, num_inference_steps: 25


  0%|          | 0/25 [00:00<?, ?it/s]

2026-10-06 17:22:46.565 | INFO     | ov_ace_helper:text2music_diffusion_process:870 - repaint start from 20 add 0.37919461727142334 level of noise


...

100%|██████████| 25/25 [00:01<00:00, 18.29it/s]

  0%|          | 0/1 [00:00<?, ?it/s]

2026-10-06 17:22:49.645 | INFO     | acestep.pipeline_ace_step:save_wav_file:1390 - Provided save_path '/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs' is a directory. Appending timestamped filename.


2026-10-06 17:22:49.645 | INFO     | acestep.pipeline_ace_step:save_wav_file:1399 - Saving audio to /home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs/output_20261006172249_0.wav using backend soundfile


100%|██████████| 1/1 [00:00<00:00, 51.09it/s]

## ACE Step with LoRA
[back to top ⬆️](#Table-of-contents:)


LoRA is a technique that allows to fine-tune large models with a small number of parameters. ACE Step support LoRA, more information about it can be find [here](https://github.com/ace-step/ACE-Step?tab=readme-ov-file#-applications).

Let's try LoRA. To use LoRA for ACE Step and OpenVINO, LoRA should be applied for the model and model should be converted to IR format.

### Load LoRA and apply for Transformer models for ACE Step pipeline
[back to top ⬆️](#Table-of-contents:)

In [16]:
pipeline.load_lora("ACE-Step/ACE-Step-v1-chinese-rap-LoRA", 1)

Fetching 4 files:   0%|          | 0/4 [00:00<?, ?it/s]

config.json: 0.00B [00:00, ?B/s]

pytorch_lora_weights.safetensors:   0%|          | 0.00/524M [00:00<?, ?B/s]

.gitattributes: 0.00B [00:00, ?B/s]

README.md: 0.00B [00:00, ?B/s]

2026-10-06 17:23:51.245 | INFO     | acestep.pipeline_ace_step:load_lora:1424 - Loading lora weights from: ACE-Step/ACE-Step-v1-chinese-rap-LoRA download path is: /home/amd/.cache/ace-step/checkpoints/models--ACE-Step--ACE-Step-v1-chinese-rap-LoRA/snapshots/e40a223cb69a60ba8a8c46752987c152b8a5f828 weight: 1


### Convert models with LoRA and load to OpenVINO pipeline
[back to top ⬆️](#Table-of-contents:)

In [17]:
from ov_ace_helper import convert_transformer_models

ov_models_lora = "ov_models_lora"

convert_transformer_models(pipeline, ov_models_lora)

ov_pipeline.load_lora(ov_models_lora)

⌛ Convert Transformer Encoder with Entropy Rectifying Guidance model


✅ Transformer Encoder with Entropy Rectifying Guidance model converted
⌛ Convert Transformer Decoder with Entropy Rectifying Guidance model


✅ Transformer Decoder with Entropy Rectifying Guidance model converted


### Run Inference with LoRA  
[back to top ⬆️](#Table-of-contents:)

In [18]:
import IPython.display as ipd

inputs["prompt"] = "chopper rap, female, rap flow, groovy, singing, smooth Rhythm, synthesizer lead, heavy bassline"
result = ov_pipeline(**inputs)

orig_path = result[0]
display(ipd.Audio(result[0]))

2026-10-06 17:24:40.712 | INFO     | acestep.pipeline_ace_step:__call__:1488 - Model loaded in 0.24 seconds.


2026-10-06 17:24:40.731 | INFO     | ov_ace_helper:text2music_diffusion_process:623 - cfg_type: apg, guidance_scale: 15.0, omega_scale: 10.0


2026-10-06 17:24:40.734 | INFO     | ov_ace_helper:text2music_diffusion_process:807 - start_idx: 6, end_idx: 18, num_inference_steps: 25


  0%|          | 0/25 [00:00<?, ?it/s]

  4%|▍         | 1/25 [00:00<00:08,  2.83it/s]

...

100%|██████████| 25/25 [00:10<00:00,  2.35it/s]

  0%|          | 0/1 [00:00<?, ?it/s]

2026-10-06 17:24:52.707 | INFO     | acestep.pipeline_ace_step:save_wav_file:1390 - Provided save_path '/home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs' is a directory. Appending timestamped filename.


2026-10-06 17:24:52.707 | INFO     | acestep.pipeline_ace_step:save_wav_file:1399 - Saving audio to /home/amd/Desktop/OpenVINO-Notebooks-on-AMD/results/ace-step-music-generation/workdir-cpu/outputs/output_20261006172452_0.wav using backend soundfile


100%|██████████| 1/1 [00:00<00:00, 48.28it/s]

### Deactivate LoRA
[back to top ⬆️](#Table-of-contents:)

To unload LoRA and use original IRs we will run `load_lora` and provide `none` instead of path.

In [19]:
ov_pipeline.load_lora("none")

## Interactive demo
[back to top ⬆️](#Table-of-contents:)
